# Constrained double pendulum

This notebook demonstrates the symbolic workflow in the Lagrangian machinery. The idea is to keep the problem-specific setup explicit: define the coordinates, write the Lagrangian, compute the unconstrained accelerations, assemble the constraint Jacobian, and then enforce the constraints with the helper functions from `quivira._lagrangian_math`.

The example is a double pendulum fixed at the top, released from a sideways configuration, and allowed to swing under gravity.

In [9]:
import numpy as np
import matplotlib.pyplot as plt
from matplotlib.animation import FuncAnimation
import heyoka as hy
from IPython.display import HTML
import quivira as qv

The generalized coordinates are the center positions and orientations of the two rods. We keep the model explicit:

$$q = (x_0, y_0, \theta_0, x_1, y_1, \theta_1)$$

and

$$\dot q = (\dot x_0, \dot y_0, \dot \theta_0, \dot x_1, \dot y_1, \dot \theta_1).$$

The first rod is pinned at the top and the second rod is connected to the first, so the geometry is encoded by algebraic constraints rather than by a built-in mechanism model.

In [10]:
# Generalized coordinates: center positions and orientations of the two rods.
# q = [x0, y0, theta0, x1, y1, theta1]
# qd = [xd0, yd0, thetad0, xd1, yd1, thetad1]
q = list(hy.make_vars("x0", "y0", "theta0", "x1", "y1", "theta1"))
qd = list(hy.make_vars("xd0", "yd0", "thetad0", "xd1", "yd1", "thetad1"))

The Lagrangian is assembled from the kinetic and potential energies:

$$
T = \frac{1}{2} m_0 (\dot x_0^2 + \dot y_0^2)
  + \frac{1}{24} m_0 L_0^2 \dot \theta_0^2
  + \frac{1}{2} m_1 (\dot x_1^2 + \dot y_1^2)
  + \frac{1}{24} m_1 L_1^2 \dot \theta_1^2,
$$

and

$$
V = m_0 g y_0 + m_1 g y_1.
$$

So the dynamics are governed by

$$
L = T - V.
$$

In [11]:
L0 = 1.0
L1 = 1.0
m0 = 1.0
m1 = 1.0
g = 9.81

# Kinetic and potential energies for the two rigid rods. Each rod contributes
# center-of-mass translational energy and rotational energy about its center.
T = 0.5 * m0 * (qd[0] ** 2 + qd[1] ** 2)
T += 0.5 * m0 * (L0 ** 2) * (qd[2] ** 2) / 12
T += 0.5 * m1 * (qd[3] ** 2 + qd[4] ** 2)
T += 0.5 * m1 * (L1 ** 2) * (qd[5] ** 2) / 12

V = m0 * g * q[1] + m1 * g * q[4]
L = T - V

The constraints encode the geometry of the linkage. For the first rod the center must satisfy

$$
\begin{aligned}
F_1 &= x_0 - \frac{L_0}{2}\cos\theta_0, \\
F_2 &= y_0 - \frac{L_0}{2}\sin\theta_0.
\end{aligned}
$$

For the second rod we link its center to the end of the first rod:

$$
\begin{aligned}
F_3 &= x_1 - x_0 - \frac{L_0}{2}\cos\theta_0 - \frac{L_1}{2}\cos\theta_1, \\
F_4 &= y_1 - y_0 - \frac{L_0}{2}\sin\theta_0 - \frac{L_1}{2}\sin\theta_1.
\end{aligned}
$$

In [12]:
# Top attachment: the first rod starts at the origin and is anchored there.
# The second rod connects to the end of the first rod.
F = np.asarray([
    q[0] - 0.5 * L0 * hy.cos(q[2]),
    q[1] - 0.5 * L0 * hy.sin(q[2]),
    q[3] - q[0] - 0.5 * L0 * hy.cos(q[2]) - 0.5 * L1 * hy.cos(q[5]),
    q[4] - q[1] - 0.5 * L0 * hy.sin(q[2]) - 0.5 * L1 * hy.sin(q[5]),
], dtype=object)

The constrained equations of motion are assembled in first-order ODE form. The accelerations are derived from the Lagrangian and adjusted to satisfy the constraints. The result pairs each coordinate with its velocity and each velocity with its constrained acceleration.

In [13]:
ode_system = qv.build_ode_equations_of_motion(L, F, q, qd)

We initialize the system from a non-equilibrium sideways pose, with both rods tilted away from vertical and all velocities set to zero:

$$
\theta_0 = 1.1, \qquad \theta_1 = -1.5, \qquad \dot q = 0.
$$

The remaining inital state values are calculated from those. This gives a clean starting condition: the system begins at rest and the motion is driven by gravity.

In [14]:
# Start from a sideways double-pendulum configuration with zero initial speeds.
theta0 = 1.1
theta1 = -1.5

x0 = 0.5 * L0 * np.cos(theta0)
y0 = 0.5 * L0 * np.sin(theta0)
x1 = x0 + 0.5 * L0 * np.cos(theta0) + 0.5 * L1 * np.cos(theta1)
y1 = y0 + 0.5 * L0 * np.sin(theta0) + 0.5 * L1 * np.sin(theta1)

state0 = [x0, y0, theta0, x1, y1, theta1, 0.0, 0.0, 0.0, 0.0, 0.0, 0.0]

Heyoka’s Taylor-adaptive integrator advances the system from its initial state using Taylor-based time integration. The initial state lists the coordinates first, followed by the velocities. Recording the state after each step gives the trajectory used for the animation.

In [15]:
integrator = hy.taylor_adaptive(ode_system, state0)

history = [np.array(integrator.state, dtype=float).copy()]
for _ in range(400):
    integrator.propagate_for(0.02)
    history.append(np.array(integrator.state, dtype=float).copy())

history = np.asarray(history)
print('Final state:')
print(history[-1])
print('History shape:', history.shape)

Final state:
[ -0.49924647   0.02744023  -3.1965007   -1.20266405  -0.40153399
 -27.12417481   0.04042216   0.73543913  -1.47309833  -3.1895426
   2.93384369  -7.16538857]
History shape: (401, 12)


In [16]:
# Draw the rods as line segments from their anchor points.
fig, ax = plt.subplots(figsize=(6, 6))
ax.set_aspect('equal')
ax.grid(True)
ax.set_xlabel('x')
ax.set_ylabel('y')

rod0_line, = ax.plot([], [], 'o-', lw=3, color='tab:blue')
rod1_line, = ax.plot([], [], 'o-', lw=3, color='tab:orange')
trail, = ax.plot([], [], '-', lw=1, alpha=0.6, color='black')

def rod_points(state, rod_length):
    x, y, theta = state[0], state[1], state[2]
    u = np.array([np.cos(theta), np.sin(theta)])
    start = np.array([x, y]) - 0.5 * rod_length * u
    end = np.array([x, y]) + 0.5 * rod_length * u
    return start, end

def init_anim():
    rod0_line.set_data([], [])
    rod1_line.set_data([], [])
    trail.set_data([], [])
    return rod0_line, rod1_line, trail

def update_anim(frame):
    state = history[frame]
    x0, y0, theta0, x1, y1, theta1 = state[:6]

    start0, end0 = rod_points(np.array([x0, y0, theta0]), L0)
    start1, end1 = rod_points(np.array([x1, y1, theta1]), L1)

    rod0_line.set_data([start0[0], end0[0]], [start0[1], end0[1]])
    rod1_line.set_data([start1[0], end1[0]], [start1[1], end1[1]])

    tip_x = history[: frame + 1, 3] + 0.5 * L1 * np.cos(history[: frame + 1, 5])
    tip_y = history[: frame + 1, 4] + 0.5 * L1 * np.sin(history[: frame + 1, 5])
    trail.set_data(tip_x, tip_y)

    x_min = min(0.0, *history[:frame + 1, 0], *tip_x) - 0.5
    x_max = max(0.0, *history[:frame + 1, 0], *tip_x) + 0.5
    y_min = min(0.0, *history[:frame + 1, 1], *tip_y) - 0.5
    y_max = max(0.0, *history[:frame + 1, 1], *tip_y) + 0.5
    ax.set_xlim(x_min, x_max)
    ax.set_ylim(y_min, y_max)

    return rod0_line, rod1_line, trail

anim = FuncAnimation(
    fig,
    update_anim,
    frames=len(history),
    interval=20,
    blit=False,
    init_func=init_anim,
)

display(HTML(anim.to_jshtml()))
plt.close(fig)